# Data mining European Parliament votes for 2014-2019 term

## Overview

Many of us are still looking at politics through an obsolete, one-dimensional lens that projects the political representatives and their votes on a left-right spectrum.
It is of course much more complex, but how can we assess that complexity, and objectively describe how our representatives and parties are positioned with respect to each other?  

This work is an attempt at seeing how our MEPs shape the EU political landscape through their votes, regardless of their party affiliation. This is done by applying data mining techniques to voting data published by the European Parliament and http://parltrack.euwiki.org.

### Reproduceability & License
The code for this project is hosted as a set of python notebooks on [GitHub](https://github.com/pduchesne/eu_votes).
In particular :
 * [details on how the data is obtained and filtered](https://github.com/pduchesne/eu_votes/blob/master/DataExtraction.ipynb)
 * [details of the data mining methodology](https://github.com/pduchesne/eu_votes/blob/master/DataMining.ipynb)
 * [All the datasets produced as part of this work](https://github.com/pduchesne/eu_votes/tree/master/computed)

All the original data and the derived data produced in the scope of this work are licensed under the [ODbL v1.0](https://www.opendatacommons.org/licenses/odbl/) license.

## 3D view of the political spectrum
The MEPs votes data have been processed using Principal Components Analysis, allowing us to reduce 10000+ votes into a few axis that best represent MEPs behaviour. By plotting MEPs along those axis, we can see how they relate to each other, and how they differ, forming the EU political space. It also pictures how countries or parties are positioned within that space.


In [1]:
import pandas as pd
import json

# Read the Principal Components that have been previously extracted
data = pd.read_json('votes_pcs.json', orient='records')

# read MEPs details
with open('meps_summary.json') as json_file:  
    meps_details = json.load(json_file)

In [19]:
import plotly.plotly as py
import plotly.graph_objs as go

# colours taken from https://en.wikipedia.org/wiki/Political_groups_of_the_European_Parliament
group_colors = {
    'PPE':'#3399FF',
    'S&D':'#FF0000',
    'ECR':'#0054A5',
    'ALDE':'#FFD700',
    'GUE/NGL':'#990000',
    'Verts/ALE':'#009900',
    'EFDD':'#24B9B9',
    'ENF':'#2B3856',
    'NA':'#999999'
}

groups = data['group'].unique()
countries = data['country'].unique()
maxVotes = data['votes_count'].max()
minVotes = data['votes_count'].min()
total_votes = maxVotes # wrong, but that's an approximation

# define marker sizes proportional to MEP number of actual votes
# marker sizes are grouped by political group
markerSizes = { group:[ 1+8*(count-minVotes)/(maxVotes-minVotes) for count in data[data['group']==group]['votes_count'] ] for group in groups }

# compute the min,max for each PrincipalComponent that will be displayed
pca_minmax = { pca_name:[data[pca_name].min(), data[pca_name].max()] for pca_name in ['PCA0', 'PCA1', 'PCA2'] }


# Button dropdown to select Political Group
grpButtonActions = [
    {'label': 'All Parties',
     'method': 'restyle',
     'args': [{
             'marker.opacity' : 1
         }]
    }
]
for idx, groupName in enumerate(groups):
    grpButtonActions.append(
        {'label': groupName,
         'method': 'restyle',
         'args': [
             {
                 #'marker.size': [ #2d array : grouped per trace, then per point within trace 
                 #    [2*size for size in markerSizes[groupName]] if idx == idx2 else markerSizes[groupName] for idx2, groupName in enumerate(groups)
                 #],
                 # 'marker.line.width'  # useless bc of https://github.com/plotly/plotly.js/issues/3796
                 'marker.opacity' : [
                     ( 1 if idx == idx2 else 0.1) for idx2, groupName in enumerate(groups) 
                  ]
             },
             # pass array of trace idxs to apply only to scatter traces, not mesh
             #[idx2 for idx2, groupName in enumerate(groups)]
         ]
        })
    

# Button dropdown to select Country
countryButtonActions = [
    {'label': 'All Countries',
     'method': 'restyle',
     'args': [{
             'marker.color' : [ group_colors[groupName] for idx2, groupName in enumerate(groups) ],
             'marker.line.color' : 'black'
         }]
    }
]
for idx, country in enumerate(countries):
    countryButtonActions.append(
        {'label': country,
         'method': 'restyle',
         'args': [
             {
                 #'marker.size': [ #2d array : grouped per trace, then per point within trace 
                 #    [2*size for size in markerSizes[groupName]] if idx == idx2 else markerSizes[groupName] for idx2, groupName in enumerate(groups)
                 #],
                 'marker.color' : [
                     [( group_colors[groupName] if mep_country == country else 'rgba(0,0,0,0.1)') for mep_country in data[data['group']==groupName]['country']] for idx2, groupName in enumerate(groups) 
                  ],
                 #'marker.opacity' : [ # DOES NOT WORK
                 #    [( 1 if mep_country == country else 0.1) for mep_country in data[data['group']==groupName]['country']] for idx2, groupName in enumerate(groups) 
                 # ],
                 'marker.line.color' : [
                     [( 'black' if mep_country == country else 'transparent') for mep_country in data[data['group']==groupName]['country']] for idx2, groupName in enumerate(groups) 
                  ],
             },
             # pass array of trace idxs to apply only to scatter traces, not mesh
             #[idx2 for idx2, groupName in enumerate(groups)]
         ]
        })
    
updatemenus=list([
    {
        'buttons':grpButtonActions,
        'direction': 'down',
        #'pad': {'r': 10, 't': 10},
        'showactive': True,
        'x': 1.2,
        'xanchor': 'right',
        'y': .65,
        'yanchor': 'top' 
    },
    {
        'buttons':countryButtonActions,
        'direction': 'down',
        #'pad': {'r': 10, 't': 10},
        'showactive': True,
        'x': 1.2,
        'xanchor': 'right',
        'y': .57,
        'yanchor': 'top' 
    }
])    
    
camera = {
    'up': {'x':0, 'y':0, 'z':1},
    'center': {'x':0, 'y':0, 'z':0},
    'eye': {'x':0, 'y':-0.5, 'z':2}
}
    
# Plotly layout
layout_comp = go.Layout(
    title="EU Political Spectrum<br><span style='font-size:60%'>Original data from http://parltrack.euwiki.org",
    hovermode='closest',
    hoverdistance=50,
#    width=500,
    height=700,
    scene = {
        'camera': camera,
        'xaxis' : {
            'range': [pca_minmax['PCA0'][0], pca_minmax['PCA0'][1]],
            'autorange': False,
            'title':'Axis 1',
            'ticklen':5,
            'zeroline':False,
            'gridwidth':2,
        },
        'yaxis' : {
            'range': [pca_minmax['PCA1'][0], pca_minmax['PCA1'][1]],
            'autorange': False,
            'title':'Axis 2',
            'ticklen':5,
            'zeroline':False,
            'gridwidth':2,
        },
        'zaxis' : {
            'range': [pca_minmax['PCA2'][0], pca_minmax['PCA2'][1]],
            'autorange': False,
            'title':'Axis 3',
            'ticklen':5,
            'zeroline':False,
            'gridwidth':2,
        }
    },
    updatemenus = updatemenus
)

# define the point groups for the scatter plot
traces = [
        {
            'x': data[data['group']==group]['PCA0'],
            'y': data[data['group']==group]['PCA1'],
            'z': data[data['group']==group]['PCA2'],
            'type': 'scatter3d',
            'name': group,
            'text': [ "<b>%s %s</b><br>%.2f %%<br>%s<br>%s<br>%s" % (
                meps_details[str(mep['mep_id'])]['surname'], 
                meps_details[str(mep['mep_id'])]['name'], 
                100*mep['votes_count']/total_votes,
                meps_details[str(mep['mep_id'])]['current_constituency'], 
                "<b>%s</b>" % meps_details[str(mep['mep_id'])]['current_group'], 
                meps_details[str(mep['mep_id'])]['country']) 
                     for idx, mep in data[data['group']==group][['votes_count', 'mep_id']].iterrows() ],
            'hoverinfo': 'text',
            'mode': 'markers',
            'marker': {'size': markerSizes[group],
                       'opacity' : 1,
                       'color': group_colors[group],
                       'line': {
                           'width':1, 
                           'color' : 'black'},
                      }
        } for group in groups
    ]

# highlight a group with a 3d mesh (cf https://plot.ly/python/3d-mesh/)
'''
mesh3d = {  'x': data[data['group']=='EFDD']['PCA0'],
            'y': data[data['group']=='EFDD']['PCA1'],
            'z': data[data['group']=='EFDD']['PCA2'],
            'type': 'mesh3d',
            'alphahull':5,
                   'opacity':0.05,
                   'color':'#0000DD'} 
traces.append(mesh3d)
'''

# Create the plotly figure and plot it
fig_comp = go.FigureWidget(data=traces, layout=layout_comp)

fig_traces = fig_comp.data 

# use widgets to have event handling
from ipywidgets import Output, VBox
#out = Output()

import webbrowser
#@out.capture(clear_output=True)
def handle_click(trace, points, state):
    if (len (points.point_inds) > 0):
        #print (points.point_inds[0])
        mep_id = data[data['group']==trace['name']]['mep_id'].values[points.point_inds[0]]
        webbrowser.open_new_tab(meps_details[str(mep_id)]['eu_homepage'])   

for trace in fig_traces : trace.on_click(handle_click)

VBox([fig_comp])


    'data': [{'hoverinfo': 'text',
              'marker': {'color': '#3399FF',
…

## Observations & Interpretation

MEP dots are sized after their attendance over the past 5 years (attendance percentage is displayed in MEP info popups). Lower attendance is most often due to MEP not having been in office for the full 5 years term.  
Each political group seems to have a trail of smaller dots drawn towards the center of the chart. This is because MEPs with smaller dots have less actual votes, and missing votes are assimilated to abstention in the scope of the data mining algorithm. This results in MEPs with less votes being drawn to a neutral position.

### Axis 1 interpretation
Axis 1 appears to be the traditional left to right political axis (albeit reversed here), with the PPE at the left, and the radical left to the right of the graph.  
Data mining results give us the votes that are most decisive in positioning an MEP along axis 1.  
The top 10 of these votes are:

In [11]:
from IPython.display import HTML, display

import re
# read PCA coefficient produced earlier
votes_pca_coeff = pd.read_json('computed/votes_pcs_coefficients.json', orient='index')
# read votes details
with open('votes_summary.json') as json_file:  
    votes_details = json.load(json_file)

def getReportUrl(reportId):
    reMatch = re.search("([A-Za-z]{1})([0-9]{1})-([0-9]+)\/([0-9]{4})$", reportId)
    return "http://www.europarl.europa.eu/doceo/document/%s-%s-%s-%s_EN.html" % (reMatch.group(1), reMatch.group(2), reMatch.group(4), reMatch.group(3))

def getTopVotesHtml(pc_idx):
    main_votes_for_pc = votes_pca_coeff['pca%d_coeff' % pc_idx].abs().sort_values(ascending=False)
    
    output = "<table><tr><th>Importance</th><th>Vote</th><th>Title</th></tr>"
    for vote_id in main_votes_for_pc[:10].index:
        output += ("<tr><td>%.4f</td><td><a href='http://www.mepvote.eu/votes.php?rcv=%s'>%s</a></td><td><a href='%s'>%s</a></td></tr>" % (main_votes_for_pc[vote_id], vote_id, vote_id, getReportUrl(votes_details[str(vote_id)]['report']), votes_details[str(vote_id)]['title']))
        #vote_id = str(data_with_count.columns[selected_indices[indices[f]]])
        #print("%d. (%f) vote %s : %s" % (f, importances[indices[f]], vote_id, votes_details[vote_id]['title'] ))
    return output + "</table>"
        
HTML(getTopVotesHtml(0))


Importance,Vote,Title
0.0196,75652,A8-0344/2016 - Richard Corbett - Am 398
0.0191,55168,A8-0175/2015 - Bernd Lange - Am 16
0.0191,71324,A8-0213/2016 - Dario Tamburrano - Am 73pc
0.0189,75981,A8-0373/2016 - Wim van de Camp - Am 1=2=3=8
0.0188,63945,A8-0009/2016 - Viviane Reding - Am 3=25
0.0188,55142,A8-0175/2015 - Bernd Lange - Am 13
0.0188,56767,A8-0228/2015 - Lynn Boylan - Am 1
0.0187,75593,A8-0344/2016 - Richard Corbett - Am 327
0.0187,81722,A8-0227/2017 - Hugues Bayet et Evelyn Regner - Am 65
0.0187,56783,A8-0228/2015 - Lynn Boylan - Am 4


(the `vote` column links to the visual vote summary, the `title` column links to the EU Parliament portal with all the related documents)  

Looking into those votes, we can see that they are about the TTIP, rail public transports, Trade in Services Agreement, the Right2Water initiative.

### Axis 2 interpretation
Likewise, we can look at the top votes defining Axis 2 to understand what it means :

In [12]:
HTML(getTopVotesHtml(1))

Importance,Vote,Title
0.0199,70720,A8-0204/2016 - Brando Benifei - § 32/2
0.0199,65116,A8-0034/2016 - Angelika Mlinar - § 11
0.0199,70732,A8-0204/2016 - Brando Benifei - § 45/2
0.0198,65146,A8-0034/2016 - Angelika Mlinar - § 32
0.0196,65145,A8-0034/2016 - Angelika Mlinar - § 29/2
0.0196,70703,A8-0204/2016 - Brando Benifei - § 15/2
0.0195,62660,RC-B8-1351/2015 - Considérant H/1
0.0195,61995,A8-0331/2015 - Sven Schulze - § 28/2
0.0194,73187,A8-0245/2016 - Marie-Christine Vergiat - Résolution
0.0194,65123,A8-0034/2016 - Angelika Mlinar - § 14/2


These votes cover refugees in the labour market, gender mainstreaming, implementation of a European microfinance facility, human rights and migration ...  
It is worth noticing that the mere title of the vote may not reflect the actual stake of the vote. In the case of the microfinance facility ([vote 61995](http://www.mepvote.eu/votes.php?rcv=61995)), the vote is actually about a specific paragraph (§ 28/2), and a closer look at the [parliament minutes](http://www.europarl.europa.eu/sides/getDoc.do?pubRef=-//EP//NONSGML+PV+20151215+RES-VOT+DOC+PDF+V0//EN&language=EN#page=28) reveals that it was all about keeping or removing the term "refugees" from the sentence "Calls on the Commission to view refugees and asylum seekers as a target group".

### Axis 3 and others
Axis 3 is interesting in that it shows a common behaviour shared by S&D and ECR (and to some extent EFDD and ENF). Looking at the decisive votes for that axis :

In [13]:
HTML(getTopVotesHtml(2))

Importance,Vote,Title
0.0425,51153,A8-0024/2015 - Georgi Pirinski - Am 12
0.0420,51151,A8-0024/2015 - Georgi Pirinski - Am 11
0.0417,77026,A8-0001/2017 - Tibor Szanyi - § 26/2
0.0415,50029,B8-0352/2014 - Am 18
0.0413,52799,A8-0101/2015 - Ingeborg Gräßle - Am 11
0.0396,51154,A8-0024/2015 - Georgi Pirinski - Am 13
0.0391,87432,A8-0392/2017 - José Blanco López - Am 37/2
0.0390,80160,A8-0153/2017 - Dennis de Jong - Résolution
0.0388,51155,A8-0024/2015 - Georgi Pirinski - Am 14
0.0381,77027,A8-0001/2017 - Tibor Szanyi - § 26/3


we see topics such as fight against fraud (where S&D proposed 4 amendments backed by ECR, see [Am 11->14](http://www.europarl.europa.eu/doceo/document/A-8-2015-0024-AM-003-014_EN.pdf#page=9)). It is however harder to figure out the common denominator right away. 

Likewise, the same investigative work can be carried out for other axes, but requires a close look at every amendment at stake to understand the common denominator to the votes. This is beyond this project, but would certainly be worth the effort.